In [2]:
import yfinance as yf
import os
import requests
import pandas as pd
from dotenv import load_dotenv

In [3]:
load_dotenv()
api_key = os.getenv("api_key")

url = f"https://api.biopharmcatalyst.com/api/user/v1/historical-catalysts?key={api_key}"

response = requests.get(url)
data = response.json()

print(data)

[{'nct_number': 'NCT05225584', 'company_name': 'Kymera Therapeutics Inc.', 'company_ticker': 'KYMR', 'conference_acronym': None, 'conference_end_date': None, 'conference_link': None, 'conference_name': None, 'conference_start_date': None, 'date': '2023-06-14', 'drug_name': 'KT-333 - (STAT3)', 'indication': 'Peripheral T-cell Lymphoma (PTCL)', 'label': 'Phase 1a', 'press_link': 'https://www.biopharmcatalyst.com/company/KYMR/news/141570', 'catalyst': 'Phase 1a data continue to demonstrate robust dose-dependent target knockdown in ongoing Phase 1a dose escalation clinical trials, with no dose limiting toxicities (DLTs) observed, noted June 14, 2023.', 'stage': 'Phase 1a', 'statuses': [{'label': 'Orphan Drug Designation (ODD)'}]}, {'nct_number': 'NCT05225584', 'company_name': 'Kymera Therapeutics Inc.', 'company_ticker': 'KYMR', 'conference_acronym': None, 'conference_end_date': None, 'conference_link': None, 'conference_name': None, 'conference_start_date': None, 'date': '2023-12-10', 'dr

In [4]:
data = pd.DataFrame(data)
data['date'] = pd.to_datetime(data['date'])
data = data[data['date']>='2021-01-01']
data = data[data['date']<='2026-06-30']

In [5]:
keptColumns = ['catalyst',
               'date',
               'company_name',
               'company_ticker',
               'drug_name',
               'nct_number',
               'label',
               'press_link',
               'stage']

catalyst_features = data.reindex(columns = keptColumns)

In [6]:
catalyst_features.to_csv("datasets/catalyst_ds.csv", index = False)

In [59]:
final_tickers = catalyst_features['company_ticker'].dropna().unique()

In [ ]:
# pull company financial features for each ticker

def getFinancialInfo(tickers):
    financial_data = []
    for ticker in tickers:
        company = yf.Ticker(ticker)
        row = {"ticker": ticker}
        for statement in [company.financials, company.balance_sheet, company.cashflow]:
            for col in statement.columns:
                if col.year == 2025:
                    row.update(statement[col])
        financial_data.append(row)
    financial_data = pd.DataFrame(financial_data).reindex(columns = 
            ['ticker', 
            'Total Revenue', 
            'Cost Of Revenue', 
            'Operating Revenue',
            'Cash And Cash Equivalents',
            'Total Debt',
            'Capital Expenditure'])
    return financial_data

In [64]:
df = getFinancialInfo(final_tickers)
df.head()

,ticker,Total Revenue,Cost Of Revenue,Operating Revenue,Cash And Cash Equivalents,Total Debt,Capital Expenditure
0,KYMR,3.921100e+07,NaN,3.921100e+07,3.570110e+08,8.225200e+07,-1.449000e+06
1,NRIX,8.398000e+07,NaN,8.398000e+07,2.469600e+08,5.573000e+07,-1.400200e+07
2,INMB,5.000000e+04,NaN,5.000000e+04,2.475100e+07,1.034000e+06,-1.042000e+06
3,ABBV,6.116000e+10,1.820400e+10,6.116000e+10,5.229000e+09,6.749600e+10,-1.214000e+09
4,FHTX,3.090900e+07,NaN,3.090900e+07,8.087600e+07,4.127000e+07,-5.000000e+04


In [65]:
df.to_csv("datasets/company_ds.csv", index = False)

In [66]:
market_data = []    
for ticker in final_tickers:
    data = yf.Ticker(ticker).history(start = '2025-01-01', end = '2026-06-30').reset_index()
    data['Ticker'] = ticker
    keptColumns = ['Date', 'Ticker', 'Open', 'Close', 'High', 'Low', 'Volume']
    data = data.reindex(columns = keptColumns)
    market_data.append(data)
market_data = pd.concat(market_data, ignore_index=True)

nbi = yf.Ticker('^NBI').history(start = '2025-01-01', end = '2026-06-30').reset_index()
nbi = nbi[['Date', 'Close']].rename(columns= {'Close':'NBI'})
market_data = pd.merge(market_data, nbi, on= 'Date', how='left')

market_data.shape
market_data.tail()

HTTP Error 404: 
$AFMD: possibly delisted; no timezone found
HTTP Error 404: 
$CVAC: possibly delisted; no timezone found
$JNCE: possibly delisted; no timezone found
$PSTV: possibly delisted; no price data found  (1d 2025-01-01 -> 2026-06-30) (Yahoo error = "Data doesn't exist for startDate = 1735707600, endDate = 1782792000")
$DAWN: possibly delisted; no timezone found
$EPIX: possibly delisted; no timezone found
$MRUS: possibly delisted; no timezone found
$ADAP: possibly delisted; no timezone found
$ASLN: possibly delisted; no timezone found
$MEIP: possibly delisted; no timezone found
$CYAD: possibly delisted; no timezone found
$ADVM: possibly delisted; no timezone found
$GMDA: possibly delisted; no timezone found
$BPMC: possibly delisted; no timezone found
$CYCC: possibly delisted; no timezone found
$CWBR: possibly delisted; no timezone found
$BCEL: possibly delisted; no timezone found
$SWTX: possibly delisted; no timezone found
$CDAK: possibly delisted; no timezone found
$KRON: poss

,Date,Ticker,Open,Close,High,Low,Volume,NBI
243237,2026-06-23 00:00:00-04:00,CURX,0.280,0.274,0.289,0.271,52600.0,6185.560059
243238,2026-06-24 00:00:00-04:00,CURX,0.270,0.265,0.278,0.265,45900.0,6279.390137
243239,2026-06-25 00:00:00-04:00,CURX,0.270,0.261,0.274,0.261,67900.0,6337.240234
243240,2026-06-26 00:00:00-04:00,CURX,0.285,0.266,0.285,0.265,50800.0,6479.970215
243241,2026-06-29 00:00:00-04:00,CURX,0.270,0.266,0.298,0.266,52300.0,6563.089844


In [67]:
market_data.to_csv("datasets/market_ds.csv", index = False)